In [57]:
from dotenv import load_dotenv
import os
import requests
import json
import tomllib
from pathlib import Path


import pandas as pd
import nflreadpy as nfl
import altair as alt
import numpy as np

import plotly.express as px
import plotly.graph_objects as go
import plotly.io as pio

from src.data_processing import utils_data_cleansing as utils
from src.data_viz import viz
from src.data_processing import stats as stats

In [58]:
CONFIG_PATH = Path("config/config.toml")

with CONFIG_PATH.open("rb") as f:
    config = tomllib.load(f)

In [3]:
# placeholder for globals
GLOBAL_SEASONS_LIST = config["GLOBAL_SEASONS_LIST"]
cfb_relative_path = config["cfb_relative_path"]
GLOBAL_MAX_DISPLAY_COLUMNS = config["GLOBAL_MAX_DISPLAY_COLUMNS"]
GLOBAL_MAX_DISPLAY_ROWS = config["GLOBAL_MAX_DISPLAY_ROWS"]
ALTAIR_DISPLAY_RENDERERS = config["ALTAIR_DISPLAY_RENDERERS"]
GLOBAL_SEASONS_LIST = config["GLOBAL_SEASONS_LIST"]
GLOBAL_WR_RECEPTIONS_MIN = config["GLOBAL_WR_RECEPTIONS_MIN"]


def_pos_list = config["def_pos_list"]
special_teams_pos_list = config["special_teams_pos_list"]

GLOBAL_POSITION_GROUPBY_COLS = config["GLOBAL_POSITION_GROUPBY_COLS"]

In [4]:
pd.set_option("display.max_columns", GLOBAL_MAX_DISPLAY_COLUMNS)
pd.set_option("display.max_rows", GLOBAL_MAX_DISPLAY_ROWS)

alt.renderers.enable(ALTAIR_DISPLAY_RENDERERS)

RendererRegistry.enable('html')

# nflreadpy
docs: https://github.com/nflverse/nflreadpy <br>



In [5]:
# Load current season play-by-play data
pbp = nfl.load_pbp()

# Load player game-level stats for multiple seasons
player_stats = nfl.load_player_stats(GLOBAL_SEASONS_LIST)

# Load all available team level stats
# team_stats = nfl.load_team_stats(seasons=True)

# nflreadpy uses Polars instead of pandas. Convert to pandas if needed:
pbp_pandas = pbp.to_pandas(use_pyarrow_extension_array=True)

In [6]:
player_stats

player_id,player_name,player_display_name,position,position_group,headshot_url,season,week,season_type,game_id,team,opponent_team,completions,attempts,passing_yards,passing_tds,passing_interceptions,sacks_suffered,sack_yards_lost,sack_fumbles,sack_fumbles_lost,passing_air_yards,passing_yards_after_catch,passing_first_downs,passing_epa,passing_cpoe,passing_2pt_conversions,pacr,passing_10,passing_16,passing_20,passing_40,carries,rushing_yards,rushing_tds,rushing_fumbles,rushing_fumbles_lost,…,fg_missed_0_19,fg_missed_20_29,fg_missed_30_39,fg_missed_40_49,fg_missed_50_59,fg_missed_60_,fg_made_list,fg_missed_list,fg_blocked_list,fg_made_distance,fg_missed_distance,fg_blocked_distance,pat_made,pat_att,pat_missed,pat_blocked,pat_pct,gwfg_made,gwfg_att,gwfg_missed,gwfg_blocked,gwfg_distance,pt_att,pt_blocked,pt_long,pt_yards,pt_inside_20,pt_out_of_bounds,pt_downed,pt_touchback,pt_fair_caught,pt_returned,pt_return_yards,pt_return_tds,pt_net_yards,fantasy_points,fantasy_points_ppr
str,str,str,str,str,str,i32,i32,str,str,str,str,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,f64,f64,i32,f64,i32,i32,i32,i32,i32,i32,i32,i32,i32,…,i32,i32,i32,i32,i32,i32,str,str,str,i32,i32,i32,i32,i32,i32,i32,f64,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,i32,f64,f64
"""00-0004091""","""P.Dawson""","""Phil Dawson""","""K""","""SPEC""","""https://static.www.nfl.com/ima…",2018,1,"""REG""","""2018_01_WAS_ARI""","""ARI""","""WAS""",0,0,0,0,0,0,0,0,0,0,0,0,null,null,0,null,0,0,0,0,0,0,0,0,0,…,0,0,0,0,0,0,null,null,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,0,0,0,0.0,0.0
"""00-0016919""","""A.Vinatieri""","""Adam Vinatieri""","""K""","""SPEC""","""https://static.www.nfl.com/ima…",2018,1,"""REG""","""2018_01_CIN_IND""","""IND""","""CIN""",0,0,0,0,0,0,0,0,0,0,0,0,null,null,0,null,0,0,0,0,0,0,0,0,0,…,0,0,0,0,1,0,"""21;38;51""","""55""",null,110,55,0,2,2,0,0,1.0,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,0,0,0,0.0,0.0
"""00-0019596""","""T.Brady""","""Tom Brady""","""QB""","""QB""","""https://static.www.nfl.com/ima…",2018,1,"""REG""","""2018_01_HOU_NE""","""NE""","""HOU""",26,39,277,3,1,2,-10,0,0,320,93,16,8.182894,2.007506,0,0.865625,13,4,4,0,1,2,0,0,0,…,0,0,0,0,0,0,null,null,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,0,0,0,21.28,21.28
"""00-0019646""","""S.Janikowski""","""Sebastian Janikowski""","""K""","""SPEC""","""https://static.www.nfl.com/ima…",2018,1,"""REG""","""2018_01_SEA_DEN""","""SEA""","""DEN""",0,0,0,0,0,0,0,0,0,0,0,0,null,null,0,null,0,0,0,0,0,0,0,0,0,…,0,0,0,1,0,0,"""35""","""46""",null,35,46,0,3,3,0,0,1.0,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,0,0,0,0.0,0.0
"""00-0020531""","""D.Brees""","""Drew Brees""","""QB""","""QB""","""https://static.www.nfl.com/ima…",2018,1,"""REG""","""2018_01_TB_NO""","""NO""","""TB""",37,45,439,3,0,1,-7,0,0,348,167,19,23.326556,13.136177,1,1.261494,17,9,6,0,0,0,0,0,0,…,0,0,0,0,0,0,null,null,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,0,0,0,31.56,31.56
…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…,…
"""00-0041556""","""R.Height""","""Romello Height""","""DE""","""DL""","""https://static.www.nfl.com/ima…",2026,4,"""REG""","""2026_04_DEN_SF""","""SF""","""DEN""",0,0,0,0,0,0,0,0,0,0,0,0,null,null,0,null,0,0,0,0,0,0,0,0,0,…,0,0,0,0,0,0,null,null,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,0,0,0,0.0,0.0
"""00-0041557""","""G.Halton""","""Gracen Halton""","""DT""","""DL""","""https://static.www.nfl.com/ima…",2026,4,"""REG""","""2026_04_DEN_SF""","""SF""","""DEN""",0,0,0,0,0,0,0,0,0,0,0,0,null,null,0,null,0,0,0,0,0,0,0,0,0,…,0,0,0,0,0,0,null,null,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,null,0,0,0,0,0,0,0,0,0,0,0.0,0.0
"""00-0041558""","""S.Roush""","""Sam Roush""","""TE""","""TE""","""https://static.www.nfl.com/ima…",2026,4,"""REG""","""2026_04_NYJ_CHI""","""CHI""","""NYJ""",0,0,0,0,0,0,0,0,0,0,0,0,null,null,0,null,0,0,0,0,0,0,0,0,0,…,0,0,0,0,0,0,null,null,null,0,0,0

In [7]:
pbp_pandas

,play_id,game_id,old_game_id,home_team,away_team,season_type,week,posteam,posteam_type,defteam,side_of_field,yardline_100,game_date,quarter_seconds_remaining,half_seconds_remaining,game_seconds_remaining,game_half,quarter_end,drive,sp,qtr,down,goal_to_go,time,yrdln,ydstogo,ydsnet,desc,play_type,yards_gained,shotgun,no_huddle,qb_dropback,qb_kneel,qb_spike,qb_scramble,pass_length,pass_location,air_yards,yards_after_catch,run_location,run_gap,field_goal_result,kick_distance,extra_point_result,two_point_conv_result,home_timeouts_remaining,away_timeouts_remaining,timeout,timeout_team,td_team,td_player_name,td_player_id,posteam_timeouts_remaining,defteam_timeouts_remaining,total_home_score,total_away_score,posteam_score,defteam_score,score_differential,posteam_score_post,defteam_score_post,score_differential_post,no_score_prob,opp_fg_prob,opp_safety_prob,opp_td_prob,fg_prob,safety_prob,td_prob,extra_point_prob,two_point_conversion_prob,ep,epa,total_home_epa,total_away_epa,total_home_rush_epa,total_away_rush_epa,total_home_pass_epa,total_away_pass_epa,air_epa,yac_epa,comp_air_epa,comp_yac_epa,total_home_comp_air_epa,total_away_comp_air_epa,total_home_comp_yac_epa,total_away_comp_yac_epa,total_home_raw_air_epa,total_away_raw_air_epa,total_home_raw_yac_epa,total_away_raw_yac_epa,wp,def_wp,home_wp,away_wp,wpa,vegas_wpa,vegas_home_wpa,home_wp_post,...,penalty_team,penalty_player_id,penalty_player_name,penalty_yards,replay_or_challenge,replay_or_challenge_result,penalty_type,defensive_two_point_attempt,defensive_two_point_conv,defensive_extra_point_attempt,defensive_extra_point_conv,safety_player_name,safety_player_id,season,cp,cpoe,series,series_success,series_result,order_sequence,start_time,time_of_day,stadium,weather,nfl_api_id,play_clock,play_deleted,play_type_nfl,special_teams_play,st_play_type,end_clock_time,end_yard_line,fixed_drive,fixed_drive_result,drive_real_start_time,drive_play_count,drive_time_of_possession,drive_first_downs,drive_inside20,drive_ended_with_score,drive_quarter_start,drive_quarter_end,drive_yards_penalized,drive_start_transition,drive_end_transition,drive_game_clock_start,drive_game_clock_end,drive_start_yard_line,drive_end_yard_line,drive_play_id_started,drive_play_id_ended,away_score,home_score,location,result,total,spread_line,total_line,div_game,roof,surface,temp,wind,home_coach,away_coach,stadium_id,game_stadium,aborted_play,success,passer,passer_jersey_number,rusher,rusher_jersey_number,receiver,receiver_jersey_number,pass,rush,first_down,special,play,passer_id,rusher_id,receiver_id,name,jersey_number,id,fantasy_player_name,fantasy_player_id,fantasy,fantasy_id,out_of_bounds,home_opening_kickoff,qb_epa,xyac_epa,xyac_mean_yardage,xyac_median_yardage,xyac_success,xyac_fd,xpass,pass_oe
0,1.0,2026_01_ARI_LAC,2026091308,LAC,ARI,REG,1,<NA>,<NA>,<NA>,<NA>,<NA>,2026-09-13,900.0,1800.0,3600.0,Half1,0.0,<NA>,0.0,1.0,<NA>,0.0,15:00,LAC 35,0.0,<NA>,GAME,<NA>,<NA>,0.0,0.0,<NA>,0.0,0.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,3.0,3.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,0.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,1.008251,-0.0,0.0,0.0,0.0,0.0,0.0,0.0,<NA>,<NA>,<NA>,<NA>,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.0,0.433208,0.566792,0.566792,0.433208,-0.0,-0.0,0.0,<NA>,...,<NA>,<NA>,<NA>,<NA>,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,2026,<NA>,<NA>,1.0,1.0,First down,1.0,"9/13/26, 16:25:43",<NA>,SoFi Stadium,"Sunny Temp: 78° F, Humidity: 70%, Wind: SW 6 mph",a9a87603-4feb-11f1-abca-2c54536568a9,0,0.0,GAME_START,0.0,<NA>,<NA>,<NA>,1.0,Touchdown,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,26,14,Home,-12,40,8.5,47.5,0,dome,matrixturf,<NA>,<NA>,Jim Harbaugh,Jonathan Gannon,LAX01,SoFi Stadium,0.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,0.0,0.0,<NA>,0.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,0.0,0.0,-0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
1,39.0,2026_01_ARI_LAC,2026091308,LAC,ARI,REG,1,ARI,away,LAC,LAC,35.0,2026-09-13,900.0,1800.0,3600.0,Half1,0.

# Pull in Data from collegefootballdata

In [8]:
college_dfs_dict = utils.load_college_data(cfb_relative_path)
college_stats_df = utils.create_college_stats_dataframe(college_dfs_dict)
college_draft_df = utils.create_college_draft_dataframe(college_dfs_dict)

# normalize data
college_stats_processed_df = utils.process_college_stats_features(college_stats_df)
college_stats_norm_df = utils.normalize_college_stats_df_cols(
    college_stats_processed_df
)

# pivot on stats data
pivot_college_stats_df = utils.aggregate_stats_df(college_stats_norm_df)

Loaded 2025_draft into DataFrame with shape (257, 24)
Loaded 2026_draft into DataFrame with shape (257, 24)
Loaded 2024_stats into DataFrame with shape (135294, 9)
Loaded 2025_stats into DataFrame with shape (141627, 9)
All stat categories are the same between 2024 and 2025 stats.
Stat categories in both 2024 and 2025: {'interceptions', 'rushing', 'receiving', 'defensive', 'punting', 'kicking', 'fumbles', 'puntReturns', 'passing', 'kickReturns'}
All draft features are the same between 2025 and 2026 stats.
Draft features in both 2025 and 2026: {'name', 'weight', 'pick', 'preDraftGrade', 'height', 'hometownInfo_longitude', 'nflAthleteId', 'nflTeam', 'hometownInfo_city', 'collegeId', 'collegeConference', 'collegeAthleteId', 'round', 'hometownInfo_latitude', 'year', 'nflTeamId', 'position', 'preDraftRanking', 'hometownInfo_country', 'hometownInfo_countyFips', 'overall', 'hometownInfo_state', 'preDraftPositionRanking', 'collegeTeam'}
Index(['collegeAthleteId', 'nflAthleteId', 'collegeId', '

In [9]:
pivot_college_stats_df

norm_col_name,season,playerId,player,position,team,conference,attempts,carries,completion_pct,completions,def_fumbles,fg_att,fg_long,fg_made,fg_pct,fg_points,fumbles_lost_total,fumbles_total,passing_interceptions,passing_tds,passing_yards,pat_attempts,pat_made,rec_long,receiving_tds,receiving_yards,receptions,rushing_long,rushing_tds,rushing_yards,yards_per_attempt,yards_per_carry,yards_per_rec
0,2024,102597,Will Rogers,QB,Washington,Big Ten,311,34,0.707,220,1,NaN,NaN,NaN,NaN,NaN,2,5,7,14,2458,NaN,NaN,NaN,NaN,NaN,NaN,20,0,-79,7.9,-2.3,NaN
1,2024,107494,Trey Sanders,RB,TCU,Big 12,NaN,13,NaN,NaN,0,NaN,NaN,NaN,NaN,NaN,0,1,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,12,0,46,NaN,3.5,NaN
2,2024,146583,John Adams,WR,Temple,American Athletic,NaN,3,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,35,1,194,16,4,0,9,NaN,3.0,12.1
3,2024,184812,Calvin Moore,CB,Cal Poly,Big Sky,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,8,0,8,1,NaN,NaN,NaN,NaN,NaN,8.0
4,2024,233186,Josh Jenkins,QB,Holy Cross,Patriot,1,NaN,0.000,0,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,1,0,0,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,0.0,NaN,NaN
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
15145,2025,5310992,Barry Kpeenu,RB,North Dakota State,MVFC,NaN,3,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,4,0,8,NaN,2.7,NaN
15146,2025,5314727,Trey Morris,RB,Houston Christian,Southland,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,11,0,11,1,NaN,NaN,NaN,NaN,NaN,11.0
15147,2025,550577,Jordan Brown,WR,Fresno State,Mountain West,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,28,1,92,10,NaN,NaN,NaN,NaN,NaN,9.2
15148,2025,553348,Jake Ryder,QB,Villanova,Coastal Athletic,1,1,1.000,1,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,0,0,0,NaN,NaN,NaN,NaN,NaN,NaN,0,0,-1,0.0,-1.0,NaN


In [10]:
college_draft_df

,collegeAthleteId,nflAthleteId,collegeId,collegeTeam,collegeConference,nflTeamId,nflTeam,year,overall,round,pick,name,position,height,weight,preDraftRanking,preDraftPositionRanking,preDraftGrade,hometownInfo_city,hometownInfo_state,hometownInfo_country,hometownInfo_latitude,hometownInfo_longitude,hometownInfo_countyFips
0,4688380,107910,2390,Miami,ACC,10,Tennessee,2025,1,1,1,Cam Ward,Quarterback,74.0,219.0,8.0,1.0,92.0,West Columbia,TX,USA,29.1438582,-95.6452249,48039
1,4685415,109188,38,Colorado,Big 12,30,Jacksonville,2025,2,1,2,Travis Hunter,Cornerback,72.0,188.0,2.0,1.0,94.0,Suwanee,GA,USA,34.0514898,-84.0712997,13135
2,4725996,109198,213,Penn State,Big Ten,19,New York,2025,3,1,3,Abdul Carter,Defensive Edge,75.0,250.0,1.0,1.0,94.0,Philadelphia,PA,USA,39.9527237,-75.1635262,42101
3,4685298,109195,99,LSU,SEC,17,New England,2025,4,1,4,Will Campbell,Offensive Tackle,78.0,319.0,14.0,2.0,91.0,Monroe,LA,USA,32.5093109,-92.1193012,22073
4,4873232,109186,130,Michigan,Big Ten,5,Cleveland,2025,5,1,5,Mason Graham,Defensive Tackle,76.0,296.0,5.0,1.0,93.0,Anaheim,CA,USA,33.8347516,-117.911732,06059
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
509,4572675,111260,77,Northwestern,Big Ten,33,Baltimore,2026,253,7,37,Evan Beerntsen,Offensive Guard,75.0,301.0,256.0,17.0,44.0,De Pere,WI,USA,44.4487476,-88.0601086,55009
510,4683151,110159,201,Oklahoma,SEC,11,Indianapolis,2026,254,7,38,Deion Burks,Wide Receiver,69.0,180.0,81.0,17.0,77.0,Belleville,MI,USA,42.2048414,-83.4852106,17163
511,2094390,111401,12,Arizona,Big 12,26,Seattle,2026,255,7,39,Michael Dansby,Cornerback,NaN,NaN,NaN,NaN,NaN,Oakland,CA,USA,37.8044557,-122.2713563,06001
512,5159802,110837,254,Utah,Big 12,7,Denver,2026,256,7,40,Dallen Bentley,Tight End,76.0,253.0,234.0,21.0,45.0,Taylorsville,UT,USA,40.6677096,-111.9385867,49035


In [11]:
# split out pivot_college_stats_df by position groups

# qb
qb_college_stats_df = pivot_college_stats_df[pivot_college_stats_df["position"] == "QB"]

# rb
rb_college_stats_df = pivot_college_stats_df[pivot_college_stats_df["position"] == "RB"]

# wr
wr_college_stats_df = pivot_college_stats_df[pivot_college_stats_df["position"] == "WR"]

# te
te_college_stats_df = pivot_college_stats_df[pivot_college_stats_df["position"] == "TE"]

# defense

te_college_stats_df

norm_col_name,season,playerId,player,position,team,conference,attempts,carries,completion_pct,completions,def_fumbles,fg_att,fg_long,fg_made,fg_pct,fg_points,fumbles_lost_total,fumbles_total,passing_interceptions,passing_tds,passing_yards,pat_attempts,pat_made,rec_long,receiving_tds,receiving_yards,receptions,rushing_long,rushing_tds,rushing_yards,yards_per_attempt,yards_per_carry,yards_per_rec
6,2024,3949586,Jake Taylor,TE,Duke,ACC,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,14,0,74,11,NaN,NaN,NaN,NaN,NaN,6.7
7,2024,4038961,Cam McCormick,TE,Miami,ACC,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,9,3,42,6,NaN,NaN,NaN,NaN,NaN,7.0
9,2024,4242373,Bentley Hanshaw,TE,Liberty,Conference USA,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,21,1,92,10,NaN,NaN,NaN,NaN,NaN,9.2
18,2024,4361014,Brant Kuithe,TE,Utah,Big 12,NaN,8,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,71,6,505,35,11,2,26,NaN,3.3,14.4
26,2024,4362248,Anthony Torres,TE,Toledo,Mid-American,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,78,9,404,31,NaN,NaN,NaN,NaN,NaN,13.0
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
15112,2025,5304568,Jack Stanton,TE,Stetson,Pioneer,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,18,0,35,7,NaN,NaN,NaN,NaN,NaN,5.0
15123,2025,5305824,Gerard Grewe,TE,Truman State,Great Lakes,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,14,0,24,2,NaN,NaN,NaN,NaN,NaN,12.0
15128,2025,5306480,Cade Hays,TE,Sul Ross State,Lone Star,NaN,2,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,1,0,-3,NaN,-1.5,NaN
15138,2025,5306774,Jalen Williams,TE,Texas Southern,SWAC,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,23,1,137,18,NaN,NaN,NaN,NaN,NaN,7.6


# Explore Player Stats from nflreadpy

In [12]:
# convert to pandas
player_stats_df = player_stats.to_pandas(use_pyarrow_extension_array=True)

player_stats_df

,player_id,player_name,player_display_name,position,position_group,headshot_url,season,week,season_type,game_id,team,opponent_team,completions,attempts,passing_yards,passing_tds,passing_interceptions,sacks_suffered,sack_yards_lost,sack_fumbles,sack_fumbles_lost,passing_air_yards,passing_yards_after_catch,passing_first_downs,passing_epa,passing_cpoe,passing_2pt_conversions,pacr,passing_10,passing_16,passing_20,passing_40,carries,rushing_yards,rushing_tds,rushing_fumbles,rushing_fumbles_lost,rushing_first_downs,rushing_epa,rushing_2pt_conversions,rushing_10,rushing_12,rushing_20,rushing_40,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,receiving_10,receiving_16,receiving_20,receiving_40,racr,target_share,air_yards_share,wopr,special_teams_tds,def_tackles_solo,def_tackles_with_assist,def_tackle_assists,def_tackles_for_loss,def_tackles_for_loss_yards,def_fumbles_forced,def_sacks,def_sack_yards,def_qb_hits,def_interceptions,def_interception_yards,def_pass_defended,def_tds,def_fumbles,def_safeties,def_punt_blocks,def_pat_blocks,def_fg_blocks,def_2pt_atts,def_2pt_made,misc_yards,fumble_recovery_own,fumble_recovery_yards_own,fumble_recovery_opp,fumble_recovery_yards_opp,fumble_recovery_tds,penalties,penalty_yards,fumbles_forced_by_opp,fumbles_not_forced,fumbles_out_of_bounds,fumbles_total,fumbles_lost_total,punt_returns,punt_return_yards,kickoff_returns,kickoff_return_yards,fg_made,fg_att,fg_missed,fg_blocked,fg_long,fg_pct,fg_made_0_19,fg_made_20_29,fg_made_30_39,fg_made_40_49,fg_made_50_59,fg_made_60_,fg_missed_0_19,fg_missed_20_29,fg_missed_30_39,fg_missed_40_49,fg_missed_50_59,fg_missed_60_,fg_made_list,fg_missed_list,fg_blocked_list,fg_made_distance,fg_missed_distance,fg_blocked_distance,pat_made,pat_att,pat_missed,pat_blocked,pat_pct,gwfg_made,gwfg_att,gwfg_missed,gwfg_blocked,gwfg_distance,pt_att,pt_blocked,pt_long,pt_yards,pt_inside_20,pt_out_of_bounds,pt_downed,pt_touchback,pt_fair_caught,pt_returned,pt_return_yards,pt_return_tds,pt_net_yards,fantasy_points,fantasy_points_ppr
0,00-0004091,P.Dawson,Phil Dawson,K,SPEC,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_WAS_ARI,ARI,WAS,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,0,<NA>,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,0.0,0.0,0.0,0,0,0,0,0,0,0,0.0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,<NA>,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,0.0,0.0
1,00-0016919,A.Vinatieri,Adam Vinatieri,K,SPEC,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_CIN_IND,IND,CIN,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,0,<NA>,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,0.0,0.0,0.0,0,0,0,0,0,0,0,0.0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,3,4,1,0,51,0.75,0,1,1,0,1,0,0,0,0,0,1,0,21;38;51,55,<NA>,110,55,0,2,2,0,0,1.0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,0.0,0.0
2,00-0019596,T.Brady,Tom Brady,QB,QB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_HOU_NE,NE,HOU,26,39,277,3,1,2,-10,0,0,320,93,16,8.182894,2.007506,0,0.865625,13,4,4,0,1,2,0,0,0,1,1.837627,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,0.0,0.0,0.0,0,0,0,0,0,0,0,0.0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,<NA>,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,21.28,21.28
3,00-0019646,S.Janikowski,Sebastian Janikowski,K,SPEC,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_SEA_DEN,SEA,DEN,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,0,<NA>,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,0.0,0.0,0.0,0,0,0,0,0,0,0,0.0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,1,2,1,0,35,0.5,0,0,1,0,0,0,0,0,0,1,0,0,35,46,<NA>,35,46,0,3,3,0,0,1.0,0,0,0,0,0,0,0,<NA>,0,0

In [13]:
player_stats_list = player_stats_df.columns

for _ in player_stats_list:
    print(_)

player_id
player_name
player_display_name
position
position_group
headshot_url
season
week
season_type
game_id
team
opponent_team
completions
attempts
passing_yards
passing_tds
passing_interceptions
sacks_suffered
sack_yards_lost
sack_fumbles
sack_fumbles_lost
passing_air_yards
passing_yards_after_catch
passing_first_downs
passing_epa
passing_cpoe
passing_2pt_conversions
pacr
passing_10
passing_16
passing_20
passing_40
carries
rushing_yards
rushing_tds
rushing_fumbles
rushing_fumbles_lost
rushing_first_downs
rushing_epa
rushing_2pt_conversions
rushing_10
rushing_12
rushing_20
rushing_40
receptions
targets
receiving_yards
receiving_tds
receiving_fumbles
receiving_fumbles_lost
receiving_air_yards
receiving_yards_after_catch
receiving_first_downs
receiving_epa
receiving_2pt_conversions
receiving_10
receiving_16
receiving_20
receiving_40
racr
target_share
air_yards_share
wopr
special_teams_tds
def_tackles_solo
def_tackles_with_assist
def_tackle_assists
def_tackles_for_loss
def_tackles_for_

# Break into useful columns by position
QB <br>
RB <br>
WR/TE <br>
DEFENSE <br>
<br>
### Useful for all positions: <br>
player_id
player_name
player_display_name
position
position_group
headshot_url
season
week
season_type
game_id
team
opponent_team
<br>

### Useful for QB <br>
completions
attempts
passing_yards
passing_tds
passing_interceptions
sacks_suffered
sack_yards_lost
sack_fumbles
sack_fumbles_lost
passing_air_yards
passing_yards_after_catch
passing_first_downs
passing_epa
passing_cpoe
passing_2pt_conversions
pacr
passing_10
passing_16
passing_20
passing_40
carries
rushing_yards
rushing_tds
rushing_fumbles
rushing_fumbles_lost
rushing_first_downs
rushing_epa
rushing_2pt_conversions
rushing_10
rushing_12
rushing_20
rushing_40
<br>

### Useful for RB: <br>
carries
rushing_yards
rushing_tds
rushing_fumbles
rushing_fumbles_lost
rushing_first_downs
rushing_epa
rushing_2pt_conversions
rushing_10
rushing_12
rushing_20
rushing_40
receptions
targets
receiving_yards
receiving_tds
receiving_fumbles
receiving_fumbles_lost
receiving_air_yards
receiving_yards_after_catch
receiving_first_downs
receiving_epa
receiving_2pt_conversions
receiving_10
receiving_16
receiving_20
receiving_40
racr
target_share
air_yards_share
<br>

### Useful for WR: <br>
receptions
targets
receiving_yards
receiving_tds
receiving_fumbles
receiving_fumbles_lost
receiving_air_yards
receiving_yards_after_catch
receiving_first_downs
receiving_epa
receiving_2pt_conversions
receiving_10
receiving_16
receiving_20
receiving_40
racr
target_share
air_yards_share
<br>

### Useful for Defense: <br>
def_tackles_solo
def_tackles_with_assist
def_tackle_assists
def_tackles_for_loss
def_tackles_for_loss_yards
def_fumbles_forced
def_sacks
def_sack_yards
def_qb_hits
def_interceptions
def_interception_yards
def_pass_defended
def_tds
def_fumbles
def_safeties
def_punt_blocks
def_pat_blocks
def_fg_blocks
def_2pt_atts
def_2pt_made
misc_yards
fumble_recovery_own
fumble_recovery_yards_own
fumble_recovery_opp
fumble_recovery_yards_opp
fumble_recovery_tds

In [14]:
# columns lists
all_positions_cols = [
    "player_id",
    "player_name",
    "player",
    "position",
    "position_group",
    "headshot_url",
    "season",
    "week",
    "season_type",
    "game_id",
    "team",
    "opponent_team",
    "data_source",
    "games_played_unit",
]

qb_cols = [
    "completions",
    "attempts",
    "passing_yards",
    "passing_tds",
    "passing_interceptions",
    "sacks_suffered",
    "sack_yards_lost",
    "sack_fumbles",
    "sack_fumbles_lost",
    "passing_air_yards",
    "passing_yards_after_catch",
    "passing_first_downs",
    "passing_epa",
    "passing_cpoe",
    "passing_2pt_conversions",
    "pacr",
    "passing_10",
    "passing_16",
    "passing_20",
    "passing_40",
    "carries",
    "rushing_yards",
    "rushing_tds",
    "rushing_fumbles",
    "rushing_fumbles_lost",
    "rushing_first_downs",
    "rushing_epa",
    "rushing_2pt_conversions",
    "rushing_10",
    "rushing_12",
    "rushing_20",
    "rushing_40",
]

rb_cols = [
    "carries",
    "rushing_yards",
    "rushing_tds",
    "rushing_fumbles",
    "rushing_fumbles_lost",
    "rushing_first_downs",
    "rushing_epa",
    "rushing_2pt_conversions",
    "rushing_10",
    "rushing_12",
    "rushing_20",
    "rushing_40",
    "receptions",
    "targets",
    "receiving_yards",
    "receiving_tds",
    "receiving_fumbles",
    "receiving_fumbles_lost",
    "receiving_air_yards",
    "receiving_yards_after_catch",
    "receiving_first_downs",
    "receiving_epa",
    "receiving_2pt_conversions",
    "receiving_10",
    "receiving_16",
    "receiving_20",
    "receiving_40",
    "racr",
    "target_share",
    "air_yards_share",
]

wr_cols = [
    "receptions",
    "targets",
    "receiving_yards",
    "receiving_tds",
    "receiving_fumbles",
    "receiving_fumbles_lost",
    "receiving_air_yards",
    "receiving_yards_after_catch",
    "receiving_first_downs",
    "receiving_epa",
    "receiving_2pt_conversions",
    "receiving_10",
    "receiving_16",
    "receiving_20",
    "receiving_40",
    "racr",
    "target_share",
    "air_yards_share",
]

def_cols = [
    "def_tackles_solo",
    "def_tackles_with_assist",
    "def_tackle_assists",
    "def_tackles_for_loss",
    "def_tackles_for_loss_yards",
    "def_fumbles_forced",
    "def_sacks",
    "def_sack_yards",
    "def_qb_hits",
    "def_interceptions",
    "def_interception_yards",
    "def_pass_defended",
    "def_tds",
    "def_fumbles",
    "def_safeties",
    "def_punt_blocks",
    "def_pat_blocks",
    "def_fg_blocks",
    "def_2pt_atts",
    "def_2pt_made",
    "misc_yards",
    "fumble_recovery_own",
    "fumble_recovery_yards_own",
    "fumble_recovery_opp",
    "fumble_recovery_yards_opp",
    "fumble_recovery_tds",
]

# Merge in College Stats Data into nflreadpy data

In [15]:
pivot_college_stats_df[["position", "player", "season"]]

norm_col_name,position,player,season
0,QB,Will Rogers,2024
1,RB,Trey Sanders,2024
2,WR,John Adams,2024
3,CB,Calvin Moore,2024
4,QB,Josh Jenkins,2024
...,...,...,...
15145,RB,Barry Kpeenu,2025
15146,RB,Trey Morris,2025
15147,WR,Jordan Brown,2025
15148,QB,Jake Ryder,2025


In [16]:
# normalize nflreadpy names
player_stats_df = utils.normalize_nflreadpy_df_cols(player_stats_df)

# drop any player_stats_df rows where position, player or season is missing
player_stats_df = player_stats_df.dropna(subset=["position", "player", "season"])

# add source columns for lineage
player_stats_df["data_source"] = "nflreadpy"
pivot_college_stats_df["data_source"] = "college_data"

# note the college states is at the season level and the nfl data is at the game level
player_stats_df["games_played_unit"] = 1
pivot_college_stats_df["games_played_unit"] = pd.NA

# combine
player_stats_df = utils.combine_college_stats_and_nflreadpy_data(
    player_stats_df, pivot_college_stats_df
)

player_stats_df

,player_id,player_name,player,position,position_group,headshot_url,season,week,season_type,game_id,team,opponent_team,completions,attempts,passing_yards,passing_tds,passing_interceptions,sacks_suffered,sack_yards_lost,sack_fumbles,sack_fumbles_lost,passing_air_yards,passing_yards_after_catch,passing_first_downs,passing_epa,passing_cpoe,passing_2pt_conversions,pacr,passing_10,passing_16,passing_20,passing_40,carries,rushing_yards,rushing_tds,rushing_fumbles,rushing_fumbles_lost,rushing_first_downs,rushing_epa,rushing_2pt_conversions,rushing_10,rushing_12,rushing_20,rushing_40,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,receiving_10,receiving_16,receiving_20,receiving_40,racr,target_share,air_yards_share,wopr,special_teams_tds,def_tackles_solo,def_tackles_with_assist,def_tackle_assists,def_tackles_for_loss,def_tackles_for_loss_yards,def_fumbles_forced,def_sacks,def_sack_yards,def_qb_hits,def_interceptions,def_interception_yards,def_pass_defended,def_tds,def_fumbles,def_safeties,def_punt_blocks,def_pat_blocks,def_fg_blocks,def_2pt_atts,def_2pt_made,misc_yards,fumble_recovery_own,fumble_recovery_yards_own,fumble_recovery_opp,fumble_recovery_yards_opp,fumble_recovery_tds,penalties,penalty_yards,fumbles_forced_by_opp,fumbles_not_forced,fumbles_out_of_bounds,fumbles_total,fumbles_lost_total,punt_returns,punt_return_yards,kickoff_returns,kickoff_return_yards,fg_made,fg_att,fg_missed,fg_blocked,fg_long,fg_pct,fg_made_0_19,fg_made_20_29,fg_made_30_39,fg_made_40_49,fg_made_50_59,fg_made_60_,fg_missed_0_19,fg_missed_20_29,fg_missed_30_39,fg_missed_40_49,fg_missed_50_59,fg_missed_60_,fg_made_list,fg_missed_list,fg_blocked_list,fg_made_distance,fg_missed_distance,fg_blocked_distance,pat_made,pat_att,pat_missed,pat_blocked,pat_pct,gwfg_made,gwfg_att,gwfg_missed,gwfg_blocked,gwfg_distance,pt_att,pt_blocked,pt_long,pt_yards,pt_inside_20,pt_out_of_bounds,pt_downed,pt_touchback,pt_fair_caught,pt_returned,pt_return_yards,pt_return_tds,pt_net_yards,fantasy_points,fantasy_points_ppr,data_source,games_played_unit,playerId,conference,completion_pct,fg_points,pat_attempts,rec_long,rushing_long,yards_per_attempt,yards_per_carry,yards_per_rec
0,00-0004091,P.Dawson,Phil Dawson,K,SPEC,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_WAS_ARI,ARI,WAS,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,0,<NA>,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,0.0,0.0,0.0,0,0,0,0,0,0,0,0.0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,<NA>,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,0.0,0.0,nflreadpy,1,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
1,00-0016919,A.Vinatieri,Adam Vinatieri,K,SPEC,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_CIN_IND,IND,CIN,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,0,<NA>,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,0.0,0.0,0.0,0,0,0,0,0,0,0,0.0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,3,4,1,0,51,0.75,0,1,1,0,1,0,0,0,0,0,1,0,21;38;51,55,<NA>,110,55,0,2,2,0,0,1.0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,0.0,0.0,nflreadpy,1,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
2,00-0019596,T.Brady,Tom Brady,QB,QB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_HOU_NE,NE,HOU,26,39,277,3,1,2,-10,0,0,320,93,16,8.182894,2.007506,0,0.865625,13,4,4,0,1,2,0,0,0,1,1.837627,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,0.0,0.0,0.0,0,0,0,0,0,0,0,0.0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,0,0,0,0,0,0,0,0,0,0,0,0,<NA>,<NA>,<NA>,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,<NA>,0,0,0,0,0,0,0,0,0,0,21.28,21.28,nflreadpy,1,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
3,00-0019646,S.Janikowski,Sebastian Janikowski,K,SPEC,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_SEA_DEN,SEA,D

# Clean String Columns to Numeric as Needed

In [17]:
# convert attempts from string to numeric
player_stats_df["attempts"] = pd.to_numeric(
    player_stats_df["attempts"], errors="coerce"
)

# convert other string columns to numeric as needed
numeric_cols = qb_cols + rb_cols + wr_cols + def_cols
numeric_cols = list(set(numeric_cols))

# convert all applicable columns to numeric
player_stats_df[numeric_cols] = player_stats_df[numeric_cols].apply(
    pd.to_numeric, errors="coerce"
)

## Dumping to CSV for Consolidation in Narrative 

In [18]:
player_stats_df.to_csv("data/combined_player_stats.csv", index=False)

# Break out into dataframes by position [QB, RB, WR/TW, DEFENSE]

In [19]:
# all_positions = player_stats_df[all_positions_cols]['position'].unique()


qb_df = player_stats_df[player_stats_df["position"] == "QB"][
    all_positions_cols + qb_cols
]
rb_df = player_stats_df[player_stats_df["position"] == "RB"][
    all_positions_cols + rb_cols
]
wr_df = player_stats_df[player_stats_df["position"] == "WR"][
    all_positions_cols + wr_cols
]
te_df = player_stats_df[player_stats_df["position"] == "TE"][
    all_positions_cols + wr_cols
]
def_df = player_stats_df[player_stats_df["position"].isin(def_pos_list)][
    all_positions_cols + def_cols
]

# all_positions

# Explore QB DataFrame

In [20]:
# convert attempts from string to numeric
qb_df["attempts"] = pd.to_numeric(qb_df["attempts"], errors="coerce")

# convert other string columns to numeric as needed
numeric_cols = [
    "completions",
    "attempts",
    "passing_yards",
    "passing_tds",
    "passing_interceptions",
    "sacks_suffered",
    "sack_yards_lost",
    "sack_fumbles",
    "sack_fumbles_lost",
    "passing_air_yards",
    "passing_yards_after_catch",
    "passing_first_downs",
    "passing_epa",
    "passing_cpoe",
    "passing_2pt_conversions",
    "pacr",
    "passing_10",
    "passing_16",
    "passing_20",
    "passing_40",
    "carries",
    "rushing_yards",
    "rushing_tds",
    "rushing_fumbles",
    "rushing_fumbles_lost",
    "rushing_first_downs",
    "rushing_epa",
    "rushing_2pt_conversions",
    "rushing_10",
    "rushing_12",
    "rushing_20",
    "rushing_40",
]

# convert all applicable columns to numeric
qb_df[numeric_cols] = qb_df[numeric_cols].apply(pd.to_numeric, errors="coerce")

In [21]:
qb_season_agg = qb_df.groupby(GLOBAL_POSITION_GROUPBY_COLS).agg(
    {
        "completions": "sum",
        "attempts": "sum",
        "passing_yards": "sum",
        "passing_tds": "sum",
        "passing_interceptions": "sum",
        "carries": "sum",
        "rushing_yards": "sum",
        "rushing_tds": "sum",
        "rushing_2pt_conversions": "sum",
        "sacks_suffered": "sum",
        "sack_yards_lost": "sum",
        "sack_fumbles": "sum",
        "sack_fumbles_lost": "sum",
        "passing_air_yards": "sum",
        "passing_yards_after_catch": "sum",
        "passing_first_downs": "sum",
        "passing_epa": "sum",
        "passing_cpoe": "mean",
        "pacr": "mean",
    }
)

# filter out 0 attempted passes
qb_season_agg = qb_season_agg[qb_season_agg["attempts"] > 0]

In [22]:
# games played per season
qb_season_agg["total_games_played"] = qb_df.groupby(GLOBAL_POSITION_GROUPBY_COLS)[
    "games_played_unit"
].sum(min_count=1)

# force to numeric to fix tpye issue
qb_season_agg["total_games_played"] = pd.to_numeric(
    qb_season_agg["total_games_played"], errors="coerce"
)

# calculate completion percentage
qb_season_agg["completion_percentage"] = (
    qb_season_agg["completions"] / qb_season_agg["attempts"] * 100
)

# calculate passing yards per game
qb_season_agg["passing_yards_per_game"] = (
    qb_season_agg["passing_yards"] / qb_season_agg["total_games_played"]
)

qb_season_agg = qb_season_agg.reset_index()

qb_season_agg

,player,position,season,data_source,completions,attempts,passing_yards,passing_tds,passing_interceptions,carries,rushing_yards,rushing_tds,rushing_2pt_conversions,sacks_suffered,sack_yards_lost,sack_fumbles,sack_fumbles_lost,passing_air_yards,passing_yards_after_catch,passing_first_downs,passing_epa,passing_cpoe,pacr,total_games_played,completion_percentage,passing_yards_per_game
0,A.J. Duffy,QB,2025,college_data,197.0,334.0,2347.0,22.0,10.0,44.0,218.0,4.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,58.982036,NaN
1,AJ Bianco,QB,2024,college_data,16.0,24.0,173.0,1.0,0.0,6.0,7.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,66.666667,NaN
2,AJ Bianco,QB,2025,college_data,27.0,45.0,188.0,1.0,1.0,13.0,10.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,60.000000,NaN
3,AJ Hairston,QB,2024,college_data,40.0,73.0,480.0,5.0,0.0,24.0,-5.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,54.794521,NaN
4,AJ Hairston,QB,2025,college_data,107.0,216.0,957.0,4.0,4.0,43.0,3.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,49.537037,NaN
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
2175,Zion Turner,QB,2024,college_data,0.0,1.0,0.0,0.0,0.0,1.0,3.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,0.000000,NaN
2176,Zion Turner,QB,2025,college_data,40.0,59.0,409.0,1.0,1.0,21.0,135.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,67.796610,NaN
2177,Zolten Osbourne,QB,2024,college_data,10.0,19.0,81.0,0.0,2.0,3.0,-34.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,52.631579,NaN
2178,Zolten Osbourne,QB,2025,college_data,167.0,305.0,2229.0,12.0,6.0,45.0,-16.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,54.754098,NaN


In [23]:
qb_season_agg

,player,position,season,data_source,completions,attempts,passing_yards,passing_tds,passing_interceptions,carries,rushing_yards,rushing_tds,rushing_2pt_conversions,sacks_suffered,sack_yards_lost,sack_fumbles,sack_fumbles_lost,passing_air_yards,passing_yards_after_catch,passing_first_downs,passing_epa,passing_cpoe,pacr,total_games_played,completion_percentage,passing_yards_per_game
0,A.J. Duffy,QB,2025,college_data,197.0,334.0,2347.0,22.0,10.0,44.0,218.0,4.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,58.982036,NaN
1,AJ Bianco,QB,2024,college_data,16.0,24.0,173.0,1.0,0.0,6.0,7.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,66.666667,NaN
2,AJ Bianco,QB,2025,college_data,27.0,45.0,188.0,1.0,1.0,13.0,10.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,60.000000,NaN
3,AJ Hairston,QB,2024,college_data,40.0,73.0,480.0,5.0,0.0,24.0,-5.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,54.794521,NaN
4,AJ Hairston,QB,2025,college_data,107.0,216.0,957.0,4.0,4.0,43.0,3.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,49.537037,NaN
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
2175,Zion Turner,QB,2024,college_data,0.0,1.0,0.0,0.0,0.0,1.0,3.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,0.000000,NaN
2176,Zion Turner,QB,2025,college_data,40.0,59.0,409.0,1.0,1.0,21.0,135.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,67.796610,NaN
2177,Zolten Osbourne,QB,2024,college_data,10.0,19.0,81.0,0.0,2.0,3.0,-34.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,52.631579,NaN
2178,Zolten Osbourne,QB,2025,college_data,167.0,305.0,2229.0,12.0,6.0,45.0,-16.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,54.754098,NaN


In [24]:
describe_cols = [
    "total_games_played",
    "completions",
    "passing_yards",
    "passing_tds",
    "passing_interceptions",
    "passing_yards_per_game",
]
qb_season_agg.describe()[describe_cols]

,total_games_played,completions,passing_yards,passing_tds,passing_interceptions,passing_yards_per_game
count,650.000000,2180.000000,2180.000000,2180.000000,2180.000000,650.000000
mean,8.310769,99.738991,1144.658716,7.715596,3.893119,161.096872
std,6.049516,115.796558,1335.773248,9.775630,4.205817,90.998316
min,1.000000,0.000000,-9.000000,0.000000,0.000000,-1.000000
25%,3.000000,8.000000,90.000000,0.000000,0.000000,82.144118
50%,6.000000,45.000000,501.500000,3.000000,2.000000,180.079545
75%,14.000000,171.000000,1961.000000,12.000000,6.250000,234.055556
max,21.000000,544.000000,6074.000000,53.000000,30.000000,371.200000


In [25]:
res = qb_season_agg[qb_season_agg["season"] == 2024]

res

,player,position,season,data_source,completions,attempts,passing_yards,passing_tds,passing_interceptions,carries,rushing_yards,rushing_tds,rushing_2pt_conversions,sacks_suffered,sack_yards_lost,sack_fumbles,sack_fumbles_lost,passing_air_yards,passing_yards_after_catch,passing_first_downs,passing_epa,passing_cpoe,pacr,total_games_played,completion_percentage,passing_yards_per_game
1,AJ Bianco,QB,2024,college_data,16.0,24.0,173.0,1.0,0.0,6.0,7.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,66.666667,NaN
3,AJ Hairston,QB,2024,college_data,40.0,73.0,480.0,5.0,0.0,24.0,-5.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,54.794521,NaN
11,AJ Simpkins,QB,2024,college_data,1.0,1.0,31.0,0.0,0.0,4.0,-1.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,100.000000,NaN
13,AJ Swann,QB,2024,college_data,2.0,4.0,10.0,0.0,0.0,0.0,0.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,50.000000,NaN
15,Aaron Philo,QB,2024,college_data,38.0,74.0,565.0,1.0,2.0,12.0,76.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,51.351351,NaN
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
2171,Zeon Chriss,QB,2024,college_data,83.0,130.0,824.0,4.0,8.0,113.0,381.0,4.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,63.846154,NaN
2173,Zevi Eckhaus,QB,2024,college_data,37.0,50.0,424.0,4.0,2.0,11.0,28.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,74.000000,NaN
2175,Zion Turner,QB,2024,college_data,0.0,1.0,0.0,0.0,0.0,1.0,3.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,0.000000,NaN
2177,Zolten Osbourne,QB,2024,college_data,10.0,19.0,81.0,0.0,2.0,3.0,-34.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,52.631579,NaN


In [26]:
year = 2024

(
    avg_total_games_played,
    avg_completions,
    avg_passing_yards,
    avg_passing_tds,
    avg_passing_interceptions,
    avg_passing_yards_per_game,
) = stats.calculate_mean_passing_stats_by_year(qb_season_agg, year)

avg_total_games_played

np.float64(9.105263157894736)

In [27]:
"""
Create additional useful statistics
- Descriptive statistics for games played, completions, passing yards, passing touchdowns, passing interceptions, passing yards per game
"""

describe_cols = [
    "total_games_played",
    "completions",
    "passing_yards",
    "passing_tds",
    "passing_interceptions",
    "passing_yards_per_game",
]
qb_season_agg.describe()[describe_cols]

avg_total_games_played = qb_season_agg["total_games_played"].mean()
avg_completions = qb_season_agg["completions"].mean()
avg_passing_yards = qb_season_agg["passing_yards"].mean()
avg_passing_tds = qb_season_agg["passing_tds"].mean()
avg_passing_interceptions = qb_season_agg["passing_interceptions"].mean()
avg_passing_yards_per_game = qb_season_agg["passing_yards_per_game"].mean()

median_total_games_played = qb_season_agg["total_games_played"].median()
median_completions = qb_season_agg["completions"].median()
median_passing_yards = qb_season_agg["passing_yards"].median()
median_passing_tds = qb_season_agg["passing_tds"].median()
median_passing_interceptions = qb_season_agg["passing_interceptions"].median()
median_passing_yards_per_game = qb_season_agg["passing_yards_per_game"].median()

In [28]:
# add fantasy points

nfl_mask = qb_season_agg["data_source"] == "nflreadpy"
qb_season_agg["fantasy_points"] = np.nan

qb_season_agg.loc[nfl_mask, "fantasy_points"] = (
    qb_season_agg.loc[nfl_mask, "rushing_yards"] * 0.1
    + qb_season_agg.loc[nfl_mask, "passing_yards"] * 0.04
    + qb_season_agg.loc[nfl_mask, "rushing_tds"] * 6
    + qb_season_agg.loc[nfl_mask, "passing_tds"] * 6
    + qb_season_agg.loc[nfl_mask, "rushing_2pt_conversions"] * 2
    - qb_season_agg.loc[nfl_mask, "sack_fumbles_lost"] * 2
    - qb_season_agg.loc[nfl_mask, "passing_interceptions"] * 2
)

qb_season_agg["avg_fantasy_points"] = np.nan
qb_season_agg["avg_fantasy_points"] = (
    qb_season_agg.loc[nfl_mask, "fantasy_points"]
    / qb_season_agg.loc[nfl_mask, "total_games_played"]
)

qb_season_agg.head()

,player,position,season,data_source,completions,attempts,passing_yards,passing_tds,passing_interceptions,carries,rushing_yards,rushing_tds,rushing_2pt_conversions,sacks_suffered,sack_yards_lost,sack_fumbles,sack_fumbles_lost,passing_air_yards,passing_yards_after_catch,passing_first_downs,passing_epa,passing_cpoe,pacr,total_games_played,completion_percentage,passing_yards_per_game,fantasy_points,avg_fantasy_points
0,A.J. Duffy,QB,2025,college_data,197.0,334.0,2347.0,22.0,10.0,44.0,218.0,4.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,58.982036,NaN,NaN,NaN
1,AJ Bianco,QB,2024,college_data,16.0,24.0,173.0,1.0,0.0,6.0,7.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,66.666667,NaN,NaN,NaN
2,AJ Bianco,QB,2025,college_data,27.0,45.0,188.0,1.0,1.0,13.0,10.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,60.000000,NaN,NaN,NaN
3,AJ Hairston,QB,2024,college_data,40.0,73.0,480.0,5.0,0.0,24.0,-5.0,1.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,54.794521,NaN,NaN,NaN
4,AJ Hairston,QB,2025,college_data,107.0,216.0,957.0,4.0,4.0,43.0,3.0,0.0,0,0,0,0,0,0,0,0,0.0,<NA>,<NA>,NaN,49.537037,NaN,NaN,NaN


In [29]:
qb_season_agg.to_csv("data/qb_season_agg.csv", index=False)

# Visuals for QB Data<br>
TODO
- Place a limit on number of games minimum before including in stats to remove outliers
- Determine bin size for histogram
- Create histogram

In [30]:
# create lists for filters
season_list = GLOBAL_SEASONS_LIST
player_list = qb_season_agg["player"].unique().tolist()

# Global Filters for All Dashboards

In [31]:
season_filter = alt.param(
    name="selected_season",
    value=2024,
    bind=alt.binding_select(options=season_list, name="Season"),
)

In [32]:
bar_chart_passing_yards = (
    (
        alt.Chart(qb_season_agg)
        .mark_bar()
        .encode(
            x=alt.X("player:N", title="Player Name"),
            y=alt.Y("passing_yards:Q", title="Passing Yards"),
            color=alt.Color("season:N", title="Season"),
            tooltip=[
                "player",
                "season",
                "passing_yards",
                "passing_tds",
                "passing_interceptions",
                "completion_percentage",
                "passing_yards_per_game",
            ],
        )
        .add_params(season_filter)
        .transform_filter(alt.datum.season == season_filter)
    )
    .properties(title="Passing Yards by Player and Season")
    .interactive()
)

mean_passing_yards_line = (
    alt.Chart(qb_season_agg)
    .transform_filter(alt.datum.season == season_filter)
    .transform_calculate(statistic="'Mean Passing Yards'")
    .mark_rule(strokeWidth=2)
    .encode(
        y=alt.Y("mean(passing_yards):Q", title="Mean Passing Yards"),
        color=alt.Color(
            "statistic:N", scale=alt.Scale(domain=["Mean Passing Yards"], range=["red"])
        ),
    )
)

chart = (bar_chart_passing_yards + mean_passing_yards_line).resolve_scale(
    color="independent"
)

chart

alt.LayerChart(...)

In [33]:
# boxplot for passing yards by season
boxplot_passing_yards = (
    alt.Chart(qb_season_agg)
    .mark_boxplot()
    .encode(
        x=alt.X("season:N", title="Season"),
        y=alt.Y("passing_yards:Q", title="Passing Yards"),
        color=alt.Color("season:N", title="Season"),
    )
    .properties(width=750, height=100, title="Passing Yards by Season")
)

boxplot_passing_yards

alt.Chart(...)

# Explore Passing Performance Relationships <br>
- Passing Yards and Total Touchdowns
- Completions and Total Touchdowns


## Heatmap of Correlations


In [34]:
# heatmap of correlations
corr = (
    qb_season_agg.select_dtypes(include="number")
    .corr()
    .reset_index()
    .melt(id_vars="index")
)
corr.columns = ["var1", "var2", "correlation"]

qb_heatmap = (
    alt.Chart(corr, title="Correlation Heatmap — QB Stats")
    .mark_rect()
    .encode(
        x=alt.X("var1:N", title=None, sort=None),
        y=alt.Y("var2:N", title=None, sort=None),
        color=alt.Color(
            "correlation:Q", scale=alt.Scale(scheme="magma", domain=[-1, 1])
        ),
        tooltip=["var1", "var2", alt.Tooltip("correlation:Q", format=".2f")],
    )
    .properties(width=500, height=500)
)

qb_heatmap

alt.Chart(...)

In [35]:
qb_season_agg.columns

Index(['player', 'position', 'season', 'data_source', 'completions',
       'attempts', 'passing_yards', 'passing_tds', 'passing_interceptions',
       'carries', 'rushing_yards', 'rushing_tds', 'rushing_2pt_conversions',
       'sacks_suffered', 'sack_yards_lost', 'sack_fumbles',
       'sack_fumbles_lost', 'passing_air_yards', 'passing_yards_after_catch',
       'passing_first_downs', 'passing_epa', 'passing_cpoe', 'pacr',
       'total_games_played', 'completion_percentage', 'passing_yards_per_game',
       'fantasy_points', 'avg_fantasy_points'],
      dtype='str')

In [36]:
qb_dashboard_df = viz.apply_agg_dashboard_filters(
    qb_season_agg, config["season_agg_filters"]["qb"]
)

qb_dashboard = viz.build_qb_dashboard(qb_dashboard_df)
out_path = "qb_dashboard.html"
qb_dashboard.save(out_path)
print(f"Saved dashboard to {out_path}")
qb_dashboard

Saved dashboard to qb_dashboard.html


alt.VConcatChart(...)

# Explore RB DataFrame

In [37]:
rb_df

,player_id,player_name,player,position,position_group,headshot_url,season,week,season_type,game_id,team,opponent_team,data_source,games_played_unit,carries,rushing_yards,rushing_tds,rushing_fumbles,rushing_fumbles_lost,rushing_first_downs,rushing_epa,rushing_2pt_conversions,rushing_10,rushing_12,rushing_20,rushing_40,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,receiving_10,receiving_16,receiving_20,receiving_40,racr,target_share,air_yards_share
25,00-0023500,F.Gore,Frank Gore,RB,RB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_TEN_MIA,MIA,TEN,nflreadpy,1,9.0,61.0,0.0,0,0,3,0.692005,0,2,1,1,0,0.0,0,0.0,0.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,0.0,0.0
27,00-0023564,D.Sproles,Darren Sproles,RB,RB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_ATL_PHI,PHI,ATL,nflreadpy,1,5.0,10.0,0.0,0,0,1,-0.412701,0,0,0,0,0,4.0,7,22.0,0.0,0,0,-3,22,1,-0.568193,0,0,0,0,0,-7.333333,0.2,-0.010526
43,00-0025394,A.Peterson,Adrian Peterson,RB,RB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_WAS_ARI,WAS,ARI,nflreadpy,1,26.0,96.0,1.0,0,0,4,0.717597,0,3,3,0,0,2.0,3,70.0,0.0,1,1,2,70,1,-0.67494,0,2,2,1,1,35.0,0.103448,0.019802
45,00-0025399,M.Lynch,Marshawn Lynch,RB,RB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_LA_OAK,LV,LA,nflreadpy,1,11.0,41.0,1.0,0,0,4,0.880488,0,1,0,0,0,2.0,2,8.0,0.0,0,0,-2,10,0,-0.262743,0,0,0,0,0,-4.0,0.052632,-0.009569
60,00-0026153,J.Stewart,Jonathan Stewart,RB,RB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_JAX_NYG,NYG,JAX,nflreadpy,1,2.0,8.0,0.0,0,0,0,-0.230811,0,0,0,0,0,0.0,0,0.0,0.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,0.0,0.0
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
166620,<NA>,<NA>,Ramon McKinney Jr.,RB,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Northeastern State,<NA>,college_data,<NA>,8.0,36.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,5.0,<NA>,94.0,1.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
166627,<NA>,<NA>,Kyjuan Taylor,RB,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Florida A&M,<NA>,college_data,<NA>,3.0,10.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,NaN,<NA>,NaN,NaN,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
166630,<NA>,<NA>,Lawrence Butler,RB,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Texas Southern,<NA>,college_data,<NA>,37.0,173.0,3.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,NaN,<NA>,NaN,NaN,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
166643,<NA>,<NA>,Barry Kpeenu,RB,<NA>,<NA>,2025,<NA>,<NA>,<NA>,North Dakota State,<NA>,college_data,<NA>,3.0,8.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,NaN,<NA>,NaN,NaN,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>


In [38]:
rb_season_agg = rb_df.groupby(GLOBAL_POSITION_GROUPBY_COLS).agg(
    {
        "carries": "sum",
        "rushing_yards": "sum",
        "rushing_tds": "sum",
        "rushing_fumbles": "sum",
        "rushing_fumbles_lost": "sum",
        "rushing_first_downs": "sum",
        "rushing_epa": "mean",
        "rushing_2pt_conversions": "sum",
        "receptions": "sum",
        "targets": "sum",
        "receiving_yards": "sum",
        "receiving_tds": "sum",
        "receiving_fumbles": "sum",
        "receiving_fumbles_lost": "sum",
        "receiving_air_yards": "sum",
        "receiving_yards_after_catch": "sum",
        "receiving_first_downs": "sum",
        "receiving_epa": "mean",
        "receiving_2pt_conversions": "sum",
        "racr": "mean",
        "target_share": "mean",
        "air_yards_share": "mean",
    }
)

### filter out any 0 carries and 0 receptions
rb_season_agg = rb_season_agg[
    (rb_season_agg["carries"] > 0) & (rb_season_agg["receptions"] > 0)
]

# games played per season
rb_season_agg["total_games_played"] = rb_df.groupby(GLOBAL_POSITION_GROUPBY_COLS)[
    "games_played_unit"
].sum(min_count=1)
rb_season_agg["total_games_played"] = pd.to_numeric(
    rb_season_agg["total_games_played"], errors="coerce"
)

# calculate rush yards per carry
rb_season_agg["rush_yards_per_carry"] = (
    rb_season_agg["rushing_yards"] / rb_season_agg["carries"]
)

# calculate rush yards per game
rb_season_agg["rush_yards_per_game"] = (
    rb_season_agg["rushing_yards"] / rb_season_agg["total_games_played"]
)

# calculate receiveing yards per catch
rb_season_agg["rec_yards_per_catch"] = (
    rb_season_agg["receiving_yards"] / rb_season_agg["receptions"]
)

# calculate receiving yards per game
rb_season_agg["rec_yards_per_game"] = (
    rb_season_agg["receiving_yards"] / rb_season_agg["total_games_played"]
)

rb_season_agg = rb_season_agg.reset_index()

rb_season_agg.head()

,player,position,season,data_source,carries,rushing_yards,rushing_tds,rushing_fumbles,rushing_fumbles_lost,rushing_first_downs,rushing_epa,rushing_2pt_conversions,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,racr,target_share,air_yards_share,total_games_played,rush_yards_per_carry,rush_yards_per_game,rec_yards_per_catch,rec_yards_per_game
0,A'Marion Peterson,RB,2024,college_data,16.0,65.0,1.0,0,0,0,<NA>,0,2.0,0,13.0,0.0,0,0,0,0,0,<NA>,0,<NA>,<NA>,<NA>,NaN,4.062500,NaN,6.500000,NaN
1,A'Marion Peterson,RB,2025,college_data,49.0,177.0,3.0,0,0,0,<NA>,0,2.0,0,7.0,0.0,0,0,0,0,0,<NA>,0,<NA>,<NA>,<NA>,NaN,3.612245,NaN,3.500000,NaN
2,A.J. Gates,RB,2024,college_data,37.0,160.0,0.0,0,0,0,<NA>,0,8.0,0,96.0,0.0,0,0,0,0,0,<NA>,0,<NA>,<NA>,<NA>,NaN,4.324324,NaN,12.000000,NaN
3,A.J. Turner,RB,2024,college_data,104.0,864.0,6.0,0,0,0,<NA>,0,8.0,0,68.0,2.0,0,0,0,0,0,<NA>,0,<NA>,<NA>,<NA>,NaN,8.307692,NaN,8.500000,NaN
4,AJ Dillon,RB,2020,nflreadpy,55.0,286.0,2.0,1,0,12,0.894822,0,3.0,3,34.0,0.0,0,0,7,27,2,0.845044,0,7.916667,0.008157,0.002858,11.0,5.200000,26.0,11.333333,3.090909


In [39]:
# calculate fantasy points
nfl_mask = rb_season_agg["data_source"] == "nflreadpy"
rb_season_agg["fantasy_points"] = np.nan

rb_season_agg.loc[nfl_mask, "fantasy_points"] = (
    rb_season_agg.loc[nfl_mask, "rushing_yards"] * 0.1
    + rb_season_agg.loc[nfl_mask, "receiving_yards"] * 0.1
    + rb_season_agg.loc[nfl_mask, "receptions"] * 1
    + rb_season_agg.loc[nfl_mask, "rushing_tds"] * 6
    + rb_season_agg.loc[nfl_mask, "receiving_tds"] * 6
    + rb_season_agg.loc[nfl_mask, "rushing_2pt_conversions"] * 2
    + rb_season_agg.loc[nfl_mask, "receiving_2pt_conversions"] * 2
    - rb_season_agg.loc[nfl_mask, "rushing_fumbles"] * 2
    - rb_season_agg.loc[nfl_mask, "receiving_fumbles"] * 2
)

rb_season_agg["avg_fantasy_points"] = np.nan

rb_season_agg["avg_fantasy_points"] = (
    rb_season_agg.loc[nfl_mask, "fantasy_points"]
    / rb_season_agg.loc[nfl_mask, "total_games_played"]
)

rb_season_agg.head()

,player,position,season,data_source,carries,rushing_yards,rushing_tds,rushing_fumbles,rushing_fumbles_lost,rushing_first_downs,rushing_epa,rushing_2pt_conversions,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,racr,target_share,air_yards_share,total_games_played,rush_yards_per_carry,rush_yards_per_game,rec_yards_per_catch,rec_yards_per_game,fantasy_points,avg_fantasy_points
0,A'Marion Peterson,RB,2024,college_data,16.0,65.0,1.0,0,0,0,<NA>,0,2.0,0,13.0,0.0,0,0,0,0,0,<NA>,0,<NA>,<NA>,<NA>,NaN,4.062500,NaN,6.500000,NaN,NaN,NaN
1,A'Marion Peterson,RB,2025,college_data,49.0,177.0,3.0,0,0,0,<NA>,0,2.0,0,7.0,0.0,0,0,0,0,0,<NA>,0,<NA>,<NA>,<NA>,NaN,3.612245,NaN,3.500000,NaN,NaN,NaN
2,A.J. Gates,RB,2024,college_data,37.0,160.0,0.0,0,0,0,<NA>,0,8.0,0,96.0,0.0,0,0,0,0,0,<NA>,0,<NA>,<NA>,<NA>,NaN,4.324324,NaN,12.000000,NaN,NaN,NaN
3,A.J. Turner,RB,2024,college_data,104.0,864.0,6.0,0,0,0,<NA>,0,8.0,0,68.0,2.0,0,0,0,0,0,<NA>,0,<NA>,<NA>,<NA>,NaN,8.307692,NaN,8.500000,NaN,NaN,NaN
4,AJ Dillon,RB,2020,nflreadpy,55.0,286.0,2.0,1,0,12,0.894822,0,3.0,3,34.0,0.0,0,0,7,27,2,0.845044,0,7.916667,0.008157,0.002858,11.0,5.200000,26.0,11.333333,3.090909,45.0,4.090909


In [40]:
rb_season_agg.to_csv("data/rb_season_agg.csv", index=False)

In [41]:
# heatmap of correlations
corr = (
    rb_season_agg.select_dtypes(include="number")
    .corr()
    .reset_index()
    .melt(id_vars="index")
)
corr.columns = ["var1", "var2", "correlation"]

rb_heatmap = (
    alt.Chart(corr, title="Correlation Heatmap — RB Stats")
    .mark_rect()
    .encode(
        x=alt.X("var1:N", title=None, sort=None),
        y=alt.Y("var2:N", title=None, sort=None),
        color=alt.Color(
            "correlation:Q", scale=alt.Scale(scheme="magma", domain=[-1, 1])
        ),
        tooltip=["var1", "var2", alt.Tooltip("correlation:Q", format=".2f")],
    )
    .properties(width=500, height=500)
)

rb_heatmap

alt.Chart(...)

In [42]:
season_filter = alt.param(
    name="selected_season",
    value=2024,
    bind=alt.binding_select(options=season_list, name="Season"),
)

bar_chart_rushing_yards = (
    (
        alt.Chart(rb_season_agg)
        .mark_bar()
        .encode(
            x=alt.X("player:N", title="Player Name"),
            y=alt.Y("rushing_yards:Q", title="Rushing Yards"),
            color=alt.Color("season:N", title="Season"),
            tooltip=[
                "player",
                "season",
                "rushing_yards",
                "rushing_tds",
                "rush_yards_per_game",
            ],
        )
        .add_params(season_filter)
        .transform_filter(alt.datum.season == season_filter)
    )
    .properties(title="Rushing Yards by Player and Season")
    .interactive()
)

bar_chart_rushing_yards

alt.Chart(...)

In [43]:
rb_dashboard_df = viz.apply_agg_dashboard_filters(
    rb_season_agg, config["season_agg_filters"]["rb"]
)

rb_dashboard = viz.build_rb_dashboard(rb_dashboard_df)
out_path = "rb_dashboard.html"

rb_dashboard.save(out_path)
print(f"Saved dashboard to {out_path}")
rb_dashboard

Saved dashboard to rb_dashboard.html


alt.VConcatChart(...)

# Explore WR/TE DataFrame

In [44]:
wr_df

,player_id,player_name,player,position,position_group,headshot_url,season,week,season_type,game_id,team,opponent_team,data_source,games_played_unit,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,receiving_10,receiving_16,receiving_20,receiving_40,racr,target_share,air_yards_share
12,00-0022921,L.Fitzgerald,Larry Fitzgerald,WR,WR,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_WAS_ARI,ARI,WAS,nflreadpy,1,7.0,10,76.0,0.0,0,0,90,21,3,2.103913,0,2,2,2,0,0.844444,0.294118,0.432692
37,00-0024334,B.Marshall,Brandon Marshall,WR,WR,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_SEA_DEN,SEA,DEN,nflreadpy,1,3.0,6,46.0,1.0,0,0,83,1,3,2.754787,0,3,1,1,0,0.554217,0.181818,0.246291
44,00-0025396,T.Ginn,Ted Ginn,WR,WR,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_TB_NO,NO,TB,nflreadpy,1,5.0,6,68.0,1.0,0,0,72,4,3,4.929987,1,3,2,1,0,0.944444,0.136364,0.206897
57,00-0026035,D.Amendola,Danny Amendola,WR,WR,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_TEN_MIA,MIA,TEN,nflreadpy,1,4.0,6,26.0,0.0,0,0,50,12,0,-2.579119,0,0,0,0,0,0.52,0.214286,0.171821
64,00-0026176,J.Nelson,Jordy Nelson,WR,WR,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_LA_OAK,LV,LA,nflreadpy,1,3.0,4,23.0,0.0,0,0,23,8,1,-4.588249,0,1,1,0,0,1.0,0.105263,0.110048
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
166618,<NA>,<NA>,Kieren Jackson,WR,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Edward Waters,<NA>,college_data,<NA>,1.0,<NA>,6.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
166629,<NA>,<NA>,Jaquan Mcgee,WR,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Texas Southern,<NA>,college_data,<NA>,2.0,<NA>,24.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
166633,<NA>,<NA>,Dj Jordan,WR,<NA>,<NA>,2025,<NA>,<NA>,<NA>,USC,<NA>,college_data,<NA>,1.0,<NA>,3.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
166642,<NA>,<NA>,Tamarion LaFortune,WR,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Western Connecticut State,<NA>,college_data,<NA>,2.0,<NA>,34.0,0.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>


In [45]:
wr_season_agg = wr_df.groupby(GLOBAL_POSITION_GROUPBY_COLS).agg(
    {
        "receptions": "sum",
        "targets": "sum",
        "receiving_yards": "sum",
        "receiving_tds": "sum",
        "receiving_fumbles": "sum",
        "receiving_fumbles_lost": "sum",
        "receiving_air_yards": "sum",
        "receiving_yards_after_catch": "sum",
        "receiving_first_downs": "sum",
        "receiving_epa": "mean",
        "receiving_2pt_conversions": "sum",
        "receiving_10": "sum",
        "receiving_16": "sum",
        "receiving_20": "sum",
        "receiving_40": "sum",
        "racr": "mean",
        "target_share": "mean",
        "air_yards_share": "mean",
    }
)
# filter out 0 recptions
wr_season_agg = wr_season_agg[wr_season_agg["receptions"] > 0]

# games played per season
wr_season_agg["total_games_played"] = wr_df.groupby(GLOBAL_POSITION_GROUPBY_COLS)[
    "games_played_unit"
].sum(min_count=1)
wr_season_agg["total_games_played"] = pd.to_numeric(
    wr_season_agg["total_games_played"], errors="coerce"
)

# calculate receiveing yards per catch
wr_season_agg["rec_yards_per_catch"] = (
    wr_season_agg["receiving_yards"] / wr_season_agg["receptions"]
)

# calculate receiving yards per game
wr_season_agg["rec_yards_per_game"] = (
    wr_season_agg["receiving_yards"] / wr_season_agg["total_games_played"]
)

# Filter for minumum receptions for inclusion
wr_season_agg = wr_season_agg[wr_season_agg["receptions"] > GLOBAL_WR_RECEPTIONS_MIN]

wr_season_agg = wr_season_agg.reset_index()

wr_season_agg

,player,position,season,data_source,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,receiving_10,receiving_16,receiving_20,receiving_40,racr,target_share,air_yards_share,total_games_played,rec_yards_per_catch,rec_yards_per_game
0,A.J. Brown,WR,2019,nflreadpy,57.0,94,1115.0,8.0,1,0,1197,503,42,2.629769,0,40,22,16,8,0.944001,0.191249,0.261513,19.0,19.561404,58.684211
1,A.J. Brown,WR,2020,nflreadpy,76.0,116,1158.0,12.0,2,1,1269,453,60,4.752014,0,51,24,14,5,0.941026,0.279763,0.358458,15.0,15.236842,77.200000
2,A.J. Brown,WR,2021,nflreadpy,68.0,114,1011.0,6.0,0,0,1410,250,49,2.963629,0,49,22,14,5,0.693177,0.283858,0.448685,14.0,14.867647,72.214286
3,A.J. Brown,WR,2022,nflreadpy,101.0,167,1642.0,12.0,2,2,2040,603,67,3.053434,0,64,34,25,7,0.850701,0.284311,0.394307,20.0,16.257426,82.100000
4,A.J. Brown,WR,2023,nflreadpy,106.0,158,1456.0,7.0,2,2,1853,473,70,3.874873,0,62,29,21,3,0.793407,0.303674,0.386664,17.0,13.735849,85.647059
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
3415,Zion Steptoe,WR,2025,college_data,21.0,0,272.0,0.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,<NA>,<NA>,NaN,12.952381,NaN
3416,Zion Taylor,WR,2025,college_data,11.0,0,129.0,1.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,<NA>,<NA>,NaN,11.727273,NaN
3417,Zoe Roberts,WR,2024,college_data,12.0,0,194.0,1.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,<NA>,<NA>,NaN,16.166667,NaN
3418,Zycarl Lewis Jr.,WR,2025,college_data,24.0,0,330.0,2.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,<NA>,<NA>,NaN,13.750000,NaN


In [46]:
nfl_mask = wr_season_agg["data_source"] == "nflreadpy"

wr_season_agg["fantasy_points"] = np.nan
wr_season_agg.loc[nfl_mask, "fantasy_points"] = (
    wr_season_agg.loc[nfl_mask, "receiving_yards"] * 0.1
    + wr_season_agg.loc[nfl_mask, "receptions"] * 1
    + wr_season_agg.loc[nfl_mask, "receiving_tds"] * 6
    + wr_season_agg.loc[nfl_mask, "receiving_2pt_conversions"] * 2
    - wr_season_agg.loc[nfl_mask, "receiving_fumbles"] * 2
)

wr_season_agg["avg_fantasy_points"] = np.nan
wr_season_agg["avg_fantasy_points"] = (
    wr_season_agg.loc[nfl_mask, "fantasy_points"]
    / wr_season_agg.loc[nfl_mask, "total_games_played"]
)

wr_season_agg.head()

,player,position,season,data_source,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,receiving_10,receiving_16,receiving_20,receiving_40,racr,target_share,air_yards_share,total_games_played,rec_yards_per_catch,rec_yards_per_game,fantasy_points,avg_fantasy_points
0,A.J. Brown,WR,2019,nflreadpy,57.0,94,1115.0,8.0,1,0,1197,503,42,2.629769,0,40,22,16,8,0.944001,0.191249,0.261513,19.0,19.561404,58.684211,214.5,11.289474
1,A.J. Brown,WR,2020,nflreadpy,76.0,116,1158.0,12.0,2,1,1269,453,60,4.752014,0,51,24,14,5,0.941026,0.279763,0.358458,15.0,15.236842,77.200000,259.8,17.320000
2,A.J. Brown,WR,2021,nflreadpy,68.0,114,1011.0,6.0,0,0,1410,250,49,2.963629,0,49,22,14,5,0.693177,0.283858,0.448685,14.0,14.867647,72.214286,205.1,14.650000
3,A.J. Brown,WR,2022,nflreadpy,101.0,167,1642.0,12.0,2,2,2040,603,67,3.053434,0,64,34,25,7,0.850701,0.284311,0.394307,20.0,16.257426,82.100000,333.2,16.660000
4,A.J. Brown,WR,2023,nflreadpy,106.0,158,1456.0,7.0,2,2,1853,473,70,3.874873,0,62,29,21,3,0.793407,0.303674,0.386664,17.0,13.735849,85.647059,289.6,17.035294


In [47]:
wr_season_agg.to_csv("data/wr_season_agg.csv", index=False)

In [48]:
# heatmap of correlations
corr = (
    wr_season_agg.select_dtypes(include="number")
    .corr()
    .reset_index()
    .melt(id_vars="index")
)
corr.columns = ["var1", "var2", "correlation"]

wr_heatmap = (
    alt.Chart(corr, title="Correlation Heatmap — WR Stats")
    .mark_rect()
    .encode(
        x=alt.X("var1:N", title=None, sort=None),
        y=alt.Y("var2:N", title=None, sort=None),
        color=alt.Color(
            "correlation:Q", scale=alt.Scale(scheme="magma", domain=[-1, 1])
        ),
        tooltip=["var1", "var2", alt.Tooltip("correlation:Q", format=".2f")],
    )
    .properties(width=500, height=500)
)

wr_heatmap

alt.Chart(...)

In [49]:
wr_dashboard_df = viz.apply_agg_dashboard_filters(
    wr_season_agg, config["season_agg_filters"]["wr"]
)

wr_dashboard = viz.build_wr_dashboard(wr_dashboard_df)
out_path = "wr_dashboard.html"
wr_dashboard.save(out_path)
print(f"Saved dashboard to {out_path}")

wr_dashboard

Saved dashboard to wr_dashboard.html


alt.VConcatChart(...)

In [50]:
te_season_agg = te_df.groupby(GLOBAL_POSITION_GROUPBY_COLS).agg(
    {
        "receptions": "sum",
        "targets": "sum",
        "receiving_yards": "sum",
        "receiving_tds": "sum",
        "receiving_fumbles": "sum",
        "receiving_fumbles_lost": "sum",
        "receiving_air_yards": "sum",
        "receiving_yards_after_catch": "sum",
        "receiving_first_downs": "sum",
        "receiving_epa": "mean",
        "receiving_2pt_conversions": "sum",
        "receiving_10": "sum",
        "receiving_16": "sum",
        "receiving_20": "sum",
        "receiving_40": "sum",
        "racr": "mean",
        "target_share": "mean",
        "air_yards_share": "mean",
    }
)

# filter out 0 receptions
te_season_agg = te_season_agg[te_season_agg["receptions"] > 0]

# games played per season
te_season_agg["total_games_played"] = te_df.groupby(GLOBAL_POSITION_GROUPBY_COLS)[
    "games_played_unit"
].sum(min_count=1)
te_season_agg["total_games_played"] = pd.to_numeric(
    te_season_agg["total_games_played"], errors="coerce"
)

# calculate receiveing yards per catch
te_season_agg["rec_yards_per_catch"] = (
    te_season_agg["receiving_yards"] / te_season_agg["receptions"]
)

# calculate receiving yards per game
te_season_agg["rec_yards_per_game"] = (
    te_season_agg["receiving_yards"] / te_season_agg["total_games_played"]
)

te_season_agg = te_season_agg.reset_index()

te_season_agg

,player,position,season,data_source,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,receiving_10,receiving_16,receiving_20,receiving_40,racr,target_share,air_yards_share,total_games_played,rec_yards_per_catch,rec_yards_per_game
0,A.J. Derby,TE,2018,nflreadpy,3.0,5,48.0,1.0,0,0,44,9,3,0.667997,0,3,2,0,0,1.210498,0.061393,0.083839,3.0,16.000000,16.000000
1,AJ Barner,TE,2024,nflreadpy,30.0,38,245.0,4.0,0,0,136,164,18,0.791903,0,11,2,1,0,2.402829,0.079714,0.048153,15.0,8.166667,16.333333
2,AJ Barner,TE,2025,nflreadpy,58.0,75,586.0,7.0,3,0,335,309,31,1.931942,0,24,8,3,1,1.602316,0.127251,0.071257,20.0,10.103448,29.300000
3,AJ Barner,TE,2026,nflreadpy,9.0,15,102.0,0.0,0,0,35,90,5,-1.99375,0,4,1,1,0,2.141667,0.117949,0.04447,4.0,11.333333,25.500000
4,AJ Boarman,TE,2025,college_data,2.0,0,19.0,0.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,<NA>,<NA>,NaN,9.500000,NaN
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
2696,Zaire Mitchell-Paden,TE,2025,nflreadpy,2.0,3,17.0,0.0,0,0,13,5,1,0.381839,0,1,0,0,0,0.851852,0.041392,0.019075,3.0,8.500000,5.666667
2697,Zander Turner,TE,2025,college_data,4.0,0,15.0,0.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,<NA>,<NA>,NaN,3.750000,NaN
2698,Zeke Moore,TE,2024,college_data,4.0,0,13.0,0.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,<NA>,<NA>,NaN,3.250000,NaN
2699,Zeke Moore,TE,2025,college_data,2.0,0,7.0,0.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,<NA>,<NA>,NaN,3.500000,NaN


In [51]:
nfl_mask = te_season_agg["data_source"] == "nflreadpy"

te_season_agg["fantasy_points"] = np.nan
te_season_agg.loc[nfl_mask, "fantasy_points"] = (
    te_season_agg.loc[nfl_mask, "receiving_yards"] * 0.1
    + te_season_agg.loc[nfl_mask, "receptions"] * 1
    + te_season_agg.loc[nfl_mask, "receiving_tds"] * 6
    + te_season_agg.loc[nfl_mask, "receiving_2pt_conversions"] * 2
    - te_season_agg.loc[nfl_mask, "receiving_fumbles"] * 2
)

te_season_agg["avg_fantasy_points"] = np.nan
te_season_agg["avg_fantasy_points"] = (
    te_season_agg.loc[nfl_mask, "fantasy_points"]
    / te_season_agg.loc[nfl_mask, "total_games_played"]
)

te_season_agg.head()

,player,position,season,data_source,receptions,targets,receiving_yards,receiving_tds,receiving_fumbles,receiving_fumbles_lost,receiving_air_yards,receiving_yards_after_catch,receiving_first_downs,receiving_epa,receiving_2pt_conversions,receiving_10,receiving_16,receiving_20,receiving_40,racr,target_share,air_yards_share,total_games_played,rec_yards_per_catch,rec_yards_per_game,fantasy_points,avg_fantasy_points
0,A.J. Derby,TE,2018,nflreadpy,3.0,5,48.0,1.0,0,0,44,9,3,0.667997,0,3,2,0,0,1.210498,0.061393,0.083839,3.0,16.000000,16.000000,13.8,4.600000
1,AJ Barner,TE,2024,nflreadpy,30.0,38,245.0,4.0,0,0,136,164,18,0.791903,0,11,2,1,0,2.402829,0.079714,0.048153,15.0,8.166667,16.333333,78.5,5.233333
2,AJ Barner,TE,2025,nflreadpy,58.0,75,586.0,7.0,3,0,335,309,31,1.931942,0,24,8,3,1,1.602316,0.127251,0.071257,20.0,10.103448,29.300000,152.6,7.630000
3,AJ Barner,TE,2026,nflreadpy,9.0,15,102.0,0.0,0,0,35,90,5,-1.99375,0,4,1,1,0,2.141667,0.117949,0.04447,4.0,11.333333,25.500000,19.2,4.800000
4,AJ Boarman,TE,2025,college_data,2.0,0,19.0,0.0,0,0,0,0,0,<NA>,0,0,0,0,0,<NA>,<NA>,<NA>,NaN,9.500000,NaN,NaN,NaN


In [52]:
te_season_agg.to_csv("data/te_season_agg.csv", index=False)

In [53]:
# heatmap of correlations
corr = (
    te_season_agg.select_dtypes(include="number")
    .corr()
    .reset_index()
    .melt(id_vars="index")
)
corr.columns = ["var1", "var2", "correlation"]

te_heatmap = (
    alt.Chart(corr, title="Correlation Heatmap — TE Stats")
    .mark_rect()
    .encode(
        x=alt.X("var1:N", title=None, sort=None),
        y=alt.Y("var2:N", title=None, sort=None),
        color=alt.Color(
            "correlation:Q", scale=alt.Scale(scheme="magma", domain=[-1, 1])
        ),
        tooltip=["var1", "var2", alt.Tooltip("correlation:Q", format=".2f")],
    )
    .properties(width=500, height=500)
)

te_heatmap

alt.Chart(...)

In [54]:
te_dashboard_df = viz.apply_agg_dashboard_filters(
    te_season_agg, config["season_agg_filters"]["te"]
)

te_dashboard = viz.build_te_dashboard(te_dashboard_df)
out_path = "te_dashboard.html"
te_dashboard.save(out_path)
print(f"Saved dashboard to {out_path}")

te_dashboard

Saved dashboard to te_dashboard.html


alt.VConcatChart(...)

# Explore Defense DataFrame

In [55]:
def_df

,player_id,player_name,player,position,position_group,headshot_url,season,week,season_type,game_id,team,opponent_team,data_source,games_played_unit,def_tackles_solo,def_tackles_with_assist,def_tackle_assists,def_tackles_for_loss,def_tackles_for_loss_yards,def_fumbles_forced,def_sacks,def_sack_yards,def_qb_hits,def_interceptions,def_interception_yards,def_pass_defended,def_tds,def_fumbles,def_safeties,def_punt_blocks,def_pat_blocks,def_fg_blocks,def_2pt_atts,def_2pt_made,misc_yards,fumble_recovery_own,fumble_recovery_yards_own,fumble_recovery_opp,fumble_recovery_yards_opp,fumble_recovery_tds
6,00-0021140,J.Peppers,Julius Peppers,DE,DL,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_DAL_CAR,CAR,DAL,nflreadpy,1,0,0,1,0,0,0,0.0,0.0,1,0,0,0,0,0.0,0,0,0,0,0,0,0,0,0,0,0,0
9,00-0022247,M.Adams,Mike Adams,FS,DB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_DAL_CAR,CAR,DAL,nflreadpy,1,2,0,3,0,0,0,0.0,0.0,0,0,0,0,0,0.0,0,0,0,0,0,0,0,0,0,0,0,0
19,00-0023368,C.Wake,Cameron Wake,LB,LB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_TEN_MIA,MIA,TEN,nflreadpy,1,1,1,2,0,0,0,0.0,0.0,0,0,0,0,0,0.0,0,0,0,0,0,0,0,0,0,0,0,0
21,00-0023441,A.Jones,Adam Jones,DB,DB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_SEA_DEN,DEN,SEA,nflreadpy,1,2,0,0,1,2,0,0.0,0.0,0,1,0,1,0,0.0,0,0,0,0,0,0,0,0,0,0,0,0
22,00-0023449,D.Johnson,Derrick Johnson,LB,LB,https://static.www.nfl.com/image/private/f_aut...,2018,1,REG,2018_01_LA_OAK,LV,LA,nflreadpy,1,3,2,0,0,0,0,0.0,0.0,0,0,0,0,0,0.0,0,0,0,0,0,0,0,0,0,0,0,0
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
166628,<NA>,<NA>,Kamren Blanton,S,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Texas Southern,<NA>,college_data,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,NaN,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
166631,<NA>,<NA>,Dreshon Downey,CB,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Texas Southern,<NA>,college_data,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,NaN,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
166632,<NA>,<NA>,Matthew Cooks,LB,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Texas Southern,<NA>,college_data,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,2.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>
166635,<NA>,<NA>,Donovan Jones,LB,<NA>,<NA>,2025,<NA>,<NA>,<NA>,Texas Southern,<NA>,college_data,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,1.0,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>,<NA>


In [56]:
def_season_agg = def_df.groupby(GLOBAL_POSITION_GROUPBY_COLS).agg(
    {
        "def_tackles_solo": "sum",
        "def_tackles_with_assist": "sum",
        "def_tackle_assists": "sum",
        "def_tackles_for_loss": "sum",
        "def_tackles_for_loss_yards": "sum",
        "def_fumbles_forced": "sum",
        "def_sacks": "sum",
        "def_sack_yards": "sum",
        "def_qb_hits": "sum",
        "def_interceptions": "sum",
        "def_interception_yards": "sum",
        "def_pass_defended": "sum",
        "def_tds": "sum",
        "def_fumbles": "sum",
        "def_safeties": "sum",
        "def_punt_blocks": "sum",
        "def_pat_blocks": "sum",
        "def_fg_blocks": "sum",
        "def_2pt_atts": "sum",
        "def_2pt_made": "sum",
        "misc_yards": "sum",
        "fumble_recovery_own": "sum",
        "fumble_recovery_yards_own": "sum",
        "fumble_recovery_opp": "sum",
        "fumble_recovery_yards_opp": "sum",
        "fumble_recovery_tds": "sum",
    }
)

# games played per season
def_season_agg["total_games_played"] = def_df.groupby(GLOBAL_POSITION_GROUPBY_COLS)[
    "games_played_unit"
].sum(min_count=1)
def_season_agg["total_games_played"] = pd.to_numeric(
    def_season_agg["total_games_played"], errors="coerce"
)

# calculate solo tackles per game
def_season_agg["tackles_per_game"] = (
    def_season_agg["def_tackles_solo"] / def_season_agg["total_games_played"]
)

# calculate tackles and sacks per game
def_season_agg["total_tackles_sacks"] = (
    def_season_agg["def_tackles_solo"] + def_season_agg["def_sacks"]
)

def_season_agg = def_season_agg.reset_index()

def_season_agg

,player,position,season,data_source,def_tackles_solo,def_tackles_with_assist,def_tackle_assists,def_tackles_for_loss,def_tackles_for_loss_yards,def_fumbles_forced,def_sacks,def_sack_yards,def_qb_hits,def_interceptions,def_interception_yards,def_pass_defended,def_tds,def_fumbles,def_safeties,def_punt_blocks,def_pat_blocks,def_fg_blocks,def_2pt_atts,def_2pt_made,misc_yards,fumble_recovery_own,fumble_recovery_yards_own,fumble_recovery_opp,fumble_recovery_yards_opp,fumble_recovery_tds,total_games_played,tackles_per_game,total_tackles_sacks
0,A'Khori Jones,S,2024,college_data,0,0,0,0,0,0,0.0,0.0,0,0,0,0,0,1.0,0,0,0,0,0,0,0,0,0,0,0,0,NaN,<NA>,0.0
1,A'Shawn Robinson,DT,2018,nflreadpy,30,4,15,3,11,1,1.0,8.0,4,0,0,0,0,0.0,0,0,0,0,0,0,0,0,0,1,0,0,13.0,2.307692,31.0
2,A'Shawn Robinson,DT,2019,nflreadpy,28,4,8,2,4,1,1.5,6.0,2,0,0,3,0,0.0,0,0,0,0,0,0,0,0,0,2,3,0,12.0,2.333333,29.5
3,A'Shawn Robinson,DT,2020,nflreadpy,7,3,8,0,0,1,0.0,0.0,1,0,0,1,0,0.0,0,0,0,1,0,0,0,0,0,0,0,0,10.0,0.7,7.0
4,A'Shawn Robinson,DT,2021,nflreadpy,33,12,44,3,14,2,3.0,27.0,3,0,0,0,0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,20.0,1.65,36.0
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
11075,Zyon McCollum,CB,2023,nflreadpy,49,8,20,0,0,2,0.0,0.0,0,0,0,9,0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,18.0,2.722222,49.0
11076,Zyon McCollum,CB,2024,nflreadpy,54,3,28,2,3,0,0.0,0.0,0,2,4,18,0,0.0,0,0,0,0,0,0,0,0,0,1,0,0,18.0,3.0,54.0
11077,Zyon McCollum,CB,2025,nflreadpy,45,0,20,1,3,0,0.0,0.0,0,1,19,6,0,0.0,0,0,0,0,0,0,0,0,0,0,0,0,13.0,3.461538,45.0
11078,Zyon McCollum,CB,2026,nflreadpy,15,0,1,1,1,0,0.0,0.0,0,0,0,4,0,0.0,0,0,0,0,0,0,0,0,0,1,0,0,4.0,3.75,15.0
